# Formula-SWCT Generalization on PathMNIST

This notebook evaluates the final Formula-SWCT method on PathMNIST from the MedMNIST benchmark using an ImageNet-pretrained ResNet-18.

PathMNIST introduces a substantial domain shift from the natural-image datasets used during Formula-SWCT calibration. It consists of histopathology images and therefore provides an additional cross-domain evaluation of the frozen predictor.

The evaluation compares:

- Baseline frozen ResNet-18,
- original Single-Parameter Curvature Tuning (S-CT),
- Formula-SWCT.

Formula-SWCT follows the predict-first, train-once protocol:

1. Fit the Formula-SWCT predictor using only the calibration datasets.
2. Collect stage statistics from the PathMNIST training split.
3. Predict four stage-specific beta values before downstream training.
4. Freeze the predicted beta values.
5. Extract fixed train, validation, and test features once.
6. Train one downstream linear classifier.
7. Select the classifier checkpoint using validation accuracy.
8. Evaluate once on the test split.

No PathMNIST-specific beta sweep or beta optimization is performed by Formula-SWCT.

## Environment Setup

This notebook is designed to run independently in a fresh Google Colab runtime.

The repository is cloned, the `stage-wise-ct` branch is selected, and the required research dependencies are installed.

After dependency installation, restart the runtime before continuing.

In [1]:
!nvidia-smi

%cd /content

import os

if not os.path.exists("/content/curvature-tuning-research"):
    !git clone -b stage-wise-ct https://github.com/Syed1611/curvature-tuning-research.git
else:
    print("Repository already exists; skipping clone.")

%cd /content/curvature-tuning-research
!git checkout stage-wise-ct
!git pull

%cd /content/curvature-tuning-research/src/curvature-tuning
!git branch --show-current

Wed Sep 30 00:29:08 2026       
+-----------------------------------------------------------------------------------------+
| NVIDIA-SMI 580.82.07              Driver Version: 580.82.07      CUDA Version: 13.0     |
+-----------------------------------------+------------------------+----------------------+
| GPU  Name                 Persistence-M | Bus-Id          Disp.A | Volatile Uncorr. ECC |
| Fan  Temp   Perf          Pwr:Usage/Cap |           Memory-Usage | GPU-Util  Compute M. |
|                                         |                        |               MIG M. |
|=========================================+========================+======================|
|   0  Tesla T4                       Off |   00000000:00:04.0 Off |                    0 |
| N/A   40C    P8              9W /   70W |       3MiB /  15360MiB |      0%      Default |
|                                         |                        |                  N/A |
+-----------------------------------------+-----

In [ ]:
%pip install -q -r requirements.txt
%pip install --force-reinstall --no-cache-dir "numpy==1.26.3"

### Runtime Restart Required

Restart the Colab runtime after dependency installation.

After restarting, do not rerun the installation cell. Continue from the next cell.

In [2]:
%cd /content/curvature-tuning-research/src/curvature-tuning

import os
os.environ["WANDB_MODE"] = "disabled"

print("Working directory:", os.getcwd())

/content/curvature-tuning-research/src/curvature-tuning
Working directory: /content/curvature-tuning-research/src/curvature-tuning


In [3]:
import torch
import datasets
import numpy
import pandas
import sklearn
import tqdm
import loguru

print("Torch:", torch.__version__)
print("CUDA:", torch.cuda.is_available())

if torch.cuda.is_available():
    print("GPU:", torch.cuda.get_device_name(0))

print("datasets:", datasets.__version__)
print("NumPy:", numpy.__version__)
print("Pandas:", pandas.__version__)
print("sklearn:", sklearn.__version__)
print("tqdm:", tqdm.__version__)
print("loguru:", loguru.__version__)

Torch: 2.6.0+cu124
CUDA: True
GPU: Tesla T4
datasets: 3.4.1
NumPy: 1.26.3
Pandas: 2.2.3
sklearn: 1.5.2
tqdm: 4.66.5
loguru: 0.7.2


## PathMNIST Dataset Setup

PathMNIST is loaded through the MedMNIST dataset integration in the project's transfer-learning pipeline.

The ImageNet-pretrained ResNet-18 preprocessing pipeline is applied while using the PathMNIST dataset statistics for normalization.

This cell verifies the train, validation, and test splits before evaluation.

In [4]:
from utils.data import get_data_loaders

train_loader, test_loader, val_loader = get_data_loaders(
    "imagenet_to_medmnist/pathmnist",
    train_batch_size=32,
    test_batch_size=64,
    seed=42
)

print("Train samples:", len(train_loader.dataset))
print("Validation samples:", len(val_loader.dataset))
print("Test samples:", len(test_loader.dataset))

images, labels = next(iter(train_loader))

print("Image batch shape:", images.shape)
print("Label batch shape:", labels.shape)
print("Label min:", labels.min().item())
print("Label max:", labels.max().item())

/usr/local/lib/python3.11/dist-packages/huggingface_hub/utils/_auth.py:104: UserWarning: 
Error while fetching `HF_TOKEN` secret value from your vault: 'Requesting secret HF_TOKEN timed out. Secrets can only be fetched when running from the Colab UI.'.
You are not authenticated with the Hugging Face Hub in this notebook.
If the error persists, please let us know by opening an issue on GitHub (https://github.com/huggingface/huggingface_hub/issues/new).
  warnings.warn(


Generating train split: 0 examples [00:00, ? examples/s]

Generating test split: 0 examples [00:00, ? examples/s]

Generating validation split: 0 examples [00:00, ? examples/s]

Train samples: 89996
Validation samples: 10004
Test samples: 7180
Image batch shape: torch.Size([32, 3, 224, 224])
Label batch shape: torch.Size([32])
Label min: 0
Label max: 8


# Baseline and Original S-CT Reference

The Baseline and original Single-Parameter Curvature Tuning methods are evaluated using seeds 42, 43, and 44.

The Baseline uses the frozen ImageNet-pretrained ResNet-18 with its original ReLU activations.

S-CT performs its original validation-based search for one global beta value shared across the network.

The three-seed comparison is included so that Baseline, S-CT, and Formula-SWCT can be compared using the same seeds.

In [ ]:
%cd /content/curvature-tuning-research/src/curvature-tuning

!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds medmnist/pathmnist \
    --seed 42 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 64

/content/curvature-tuning-research/src/curvature-tuning
2026-09-28 14:20:50.237 | INFO     | __main__:main:54 - Log file: ./logs/generalization_ct_imagenet_to_medmnist-pathmnist_resnet18_seed42.log
2026-09-28 14:20:50.240 | INFO     | __main__:main:58 - Running on cuda
2026-09-28 14:20:53.007 | INFO     | __main__:main:85 - Testing baseline...
2026-09-28 14:20:53.021 | INFO     | __main__:main:88 - Number of trainable parameters: 4617
2026-09-28 14:20:53.021 | INFO     | __main__:main:89 - Starting transfer learning...
2026-09-28 14:24:29.615 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.112462, Accuracy: 21.88%
2026-09-28 14:24:29.898 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.214332, Accuracy: 14.82%
2026-09-28 14:24:30.161 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.123910, Accuracy: 20.76%
2026-09-28 14:24:30.426 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 2.009215, Accuracy: 28.59%
2026-09-28 14:24:30.729 | INF

In [5]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds medmnist/pathmnist \
    --seed 43 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 64

2026-09-30 00:31:21.216 | INFO     | __main__:main:54 - Log file: ./logs/generalization_ct_imagenet_to_medmnist-pathmnist_resnet18_seed43.log
2026-09-30 00:31:21.221 | INFO     | __main__:main:58 - Running on cuda
Downloading: "https://download.pytorch.org/models/resnet18-f37072fd.pth" to /root/.cache/torch/hub/checkpoints/resnet18-f37072fd.pth
100% 44.7M/44.7M [00:00<00:00, 172MB/s]
2026-09-30 00:31:24.528 | INFO     | __main__:main:85 - Testing baseline...
2026-09-30 00:31:24.549 | INFO     | __main__:main:88 - Number of trainable parameters: 4617
2026-09-30 00:31:24.549 | INFO     | __main__:main:89 - Starting transfer learning...
2026-09-30 00:34:54.660 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.241284, Accuracy: 12.50%
2026-09-30 00:34:54.945 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.185160, Accuracy: 15.90%
2026-09-30 00:34:55.205 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.081405, Accuracy: 22.48%
2026-09-30 00:34:55.458 

In [6]:
!WANDB_MODE=disabled python generalization_ct.py \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds medmnist/pathmnist \
    --seed 44 \
    --linear_probe_train_bs 32 \
    --linear_probe_test_bs 64

2026-09-30 04:09:14.053 | INFO     | __main__:main:54 - Log file: ./logs/generalization_ct_imagenet_to_medmnist-pathmnist_resnet18_seed44.log
2026-09-30 04:09:14.056 | INFO     | __main__:main:58 - Running on cuda
2026-09-30 04:09:16.964 | INFO     | __main__:main:85 - Testing baseline...
2026-09-30 04:09:16.985 | INFO     | __main__:main:88 - Number of trainable parameters: 4617
2026-09-30 04:09:16.985 | INFO     | __main__:main:89 - Starting transfer learning...
2026-09-30 04:12:45.577 | INFO     | train:train_epoch:47 - Epoch 1, Step 0, Loss: 2.432337, Accuracy: 9.38%
2026-09-30 04:12:45.895 | INFO     | train:train_epoch:47 - Epoch 1, Step 100, Loss: 2.461683, Accuracy: 8.14%
2026-09-30 04:12:46.273 | INFO     | train:train_epoch:47 - Epoch 1, Step 200, Loss: 2.332247, Accuracy: 12.41%
2026-09-30 04:12:46.615 | INFO     | train:train_epoch:47 - Epoch 1, Step 300, Loss: 2.190237, Accuracy: 20.72%
2026-09-30 04:12:47.078 | INFO     | train:train_epoch:47 - Epoch 1, Step 400, Loss: 2.

### Note on S-CT Numerical Stability

During the surviving seed-42 S-CT beta sweep, some candidate beta values produced non-finite (`NaN`) training losses.

The search nevertheless completed and identified a valid best candidate:

- Selected beta: **0.83**
- Best validation accuracy: **92.82%**
- Test accuracy: **87.70%**

The non-finite candidate runs are retained as part of the experimental record rather than removed from the logs.

Only successfully evaluated candidates are relevant to the final validation-based beta selection.

# Fit the Frozen Formula-SWCT Predictor

Because this notebook is intended to run independently in a fresh Google Colab runtime, the Formula-SWCT predictor is reconstructed before evaluating PathMNIST.

The formula is fitted using only the three development/calibration datasets:

| Dataset | Stage 1 | Stage 2 | Stage 3 | Stage 4 |
|---|---:|---:|---:|---:|
| Beans | 0.85 | 0.85 | 0.85 | 0.80 |
| DTD | 0.95 | 0.95 | 0.99 | 0.99 |
| Flowers102 | 0.99 | 0.95 | 0.99 | 0.90 |

For each calibration dataset and seed, five stage descriptors are measured from the frozen ImageNet-pretrained ResNet-18:

1. log activation variance,
2. activation sparsity,
3. log mean absolute activation,
4. log class-separation statistic,
5. normalized stage depth.

A ridge-regression predictor with lambda = 0.10 is fitted from these observations.

PathMNIST is not used to modify or retune the formula.

In [7]:
%cd /content/curvature-tuning-research/src/curvature-tuning

!python formula_swct.py \
    --mode fit \
    --model resnet18 \
    --pretrained_ds imagenet \
    --train_bs 32 \
    --test_bs 64

/content/curvature-tuning-research/src/curvature-tuning
FORMULA-SWCT: FIT DIRECT BETA FORMULA
No beta sweep and no downstream training are performed here.

data/train-00000-of-00001.parquet: 100% 144M/144M [00:01<00:00, 90.2MB/s] 
data/validation-00000-of-00001.parquet: 100% 18.5M/18.5M [00:01<00:00, 13.7MB/s]
data/test-00000-of-00001.parquet: 100% 17.7M/17.7M [00:00<00:00, 19.5MB/s]
Generating train split: 1034 examples [00:00, 2021.59 examples/s]
Generating validation split: 133 examples [00:00, 1417.90 examples/s]
Generating test split: 128 examples [00:00, 3647.32 examples/s]



100% 625M/625M [00:43<00:00, 14.4MB/s] 



100% 345M/345M [00:23<00:00, 14.4MB/s] 
100% 502/502 [00:00<00:00, 2.66MB/s]
100% 15.0k/15.0k [00:00<00:00, 66.5MB/s]



FITTED FORMULA
beta_hat = clip(b0 + sum(w_j * z_j), 0.7, 0.99)
intercept: 0.92166667
            log_variance: +0.05225792
                sparsity: -0.03829733
            log_mean_abs: -0.08039330
    log_class_separation: +0.04280035
         

# Formula-SWCT Evaluation on PathMNIST

The frozen Formula-SWCT predictor is evaluated on PathMNIST using seeds 42, 43, and 44.

For each seed:

- stage statistics are collected from the target training split,
- four beta values are predicted before classifier training,
- all beta values are frozen,
- features are extracted once,
- one downstream linear classifier is trained.

No target-specific beta search or beta optimization is performed.

In [ ]:
%cd /content/curvature-tuning-research/src/curvature-tuning

!python formula_swct.py \
    --mode run \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds medmnist/pathmnist \
    --seed 42 \
    --train_bs 32 \
    --test_bs 64 \
    --epochs 20

/content/curvature-tuning-research/src/curvature-tuning
FORMULA-SWCT: PREDICT FIRST, TRAIN ONCE
Dataset: medmnist/pathmnist
Seed: 42
No beta sweep. No beta optimization. No 0.78 anchor.

Predicted betas BEFORE training:
Stage 1: 0.990000
Stage 2: 0.978555
Stage 3: 0.986764
Stage 4: 0.890690
Predicted beta vector: [0.99, 0.978555, 0.986764, 0.89069]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
Loaded fixed betas: [0.99, 0.978555, 0.986764, 0.89069]

Extracting fixed Formula-SWCT features once...
Training ONE downstream classifier...
Epoch 01 | val_loss=0.363281 | val_acc=87.94%
Epoch 02 | val_loss=0.287146 | val_acc=90.14%
Epoch 03 | val_loss=0.262480 | val_acc=90.88%
Epoch 04 | val_loss=0.254495 | val_acc=91.38%
Epoch 05 | val_loss=0.247838 | val_acc=91.58%
Epoch 06 | val_loss=0.245928 | val_acc=91.59%
Epoch 07 | val_loss=0.253072 | val_acc=91.20%
Epoch 08 | val_loss=0.237019 | val_acc=91.77%
Epoch 09 | val_loss=0.244127 | val_acc=91.74%
Epoch 10 | val_loss=0.238074 | val_acc=91.74%
Epoch 1

In [ ]:
%cd /content/curvature-tuning-research/src/curvature-tuning

!python formula_swct.py \
    --mode run \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds medmnist/pathmnist \
    --seed 43 \
    --train_bs 32 \
    --test_bs 64 \
    --epochs 20

/content/curvature-tuning-research/src/curvature-tuning
FORMULA-SWCT: PREDICT FIRST, TRAIN ONCE
Dataset: medmnist/pathmnist
Seed: 43
No beta sweep. No beta optimization. No 0.78 anchor.

Predicted betas BEFORE training:
Stage 1: 0.990000
Stage 2: 0.978555
Stage 3: 0.986764
Stage 4: 0.890690
Predicted beta vector: [0.99, 0.978555, 0.986764, 0.89069]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
Loaded fixed betas: [0.99, 0.978555, 0.986764, 0.89069]

Extracting fixed Formula-SWCT features once...
Training ONE downstream classifier...
Epoch 01 | val_loss=0.354742 | val_acc=88.07%
Epoch 02 | val_loss=0.287905 | val_acc=90.08%
Epoch 03 | val_loss=0.266582 | val_acc=90.81%
Epoch 04 | val_loss=0.252573 | val_acc=91.31%
Epoch 05 | val_loss=0.247664 | val_acc=91.44%
Epoch 06 | val_loss=0.244879 | val_acc=91.45%
Epoch 07 | val_loss=0.245703 | val_acc=91.53%
Epoch 08 | val_loss=0.259238 | val_acc=90.84%
Epoch 09 | val_loss=0.242036 | val_acc=91.62%
Epoch 10 | val_loss=0.244660 | val_acc=91.62%
Epoch 1

In [ ]:
%cd /content/curvature-tuning-research/src/curvature-tuning

!python formula_swct.py \
    --mode run \
    --model resnet18 \
    --pretrained_ds imagenet \
    --transfer_ds medmnist/pathmnist \
    --seed 44 \
    --train_bs 32 \
    --test_bs 64 \
    --epochs 20

/content/curvature-tuning-research/src/curvature-tuning
FORMULA-SWCT: PREDICT FIRST, TRAIN ONCE
Dataset: medmnist/pathmnist
Seed: 44
No beta sweep. No beta optimization. No 0.78 anchor.
README.md: 7.32kB [00:00, 23.2MB/s]
medmnist.py: 4.84kB [00:00, 16.3MB/s]
Generating train split: 89996 examples [00:28, 3208.13 examples/s]
Generating test split: 7180 examples [00:02, 3423.49 examples/s]
Generating validation split: 10004 examples [00:02, 3539.25 examples/s]

Predicted betas BEFORE training:
Stage 1: 0.990000
Stage 2: 0.978555
Stage 3: 0.986764
Stage 4: 0.890690
Predicted beta vector: [0.99, 0.978555, 0.986764, 0.89069]
Stage-Wise CT ReLU counts: [3, 2, 2, 2]
Loaded fixed betas: [0.99, 0.978555, 0.986764, 0.89069]

Extracting fixed Formula-SWCT features once...
Training ONE downstream classifier...
Epoch 01 | val_loss=0.365021 | val_acc=87.63%
Epoch 02 | val_loss=0.287052 | val_acc=90.02%
Epoch 03 | val_loss=0.261886 | val_acc=91.09%
Epoch 04 | val_loss=0.258720 | val_acc=90.95%
Epoch

## Previously Completed Formula-SWCT Runs

All three Formula-SWCT PathMNIST runs were previously completed.

The predictor produced the same stage-wise beta vector for all three seeds:

**[0.990000, 0.978555, 0.986764, 0.890690]**

### Seed 42

- Best validation accuracy: **92.07%**
- Best validation epoch: **19**
- Test accuracy: **87.30%**

### Seed 43

- Best validation accuracy: **92.12%**
- Best validation epoch: **19**
- Test accuracy: **86.99%**

### Seed 44

- Best validation accuracy: **92.06%**
- Best validation epoch: **17**
- Test accuracy: **86.84%**

Across the three seeds, Formula-SWCT obtains approximately:

**87.04 ± 0.23% test accuracy**

using the sample standard deviation.

Stage 1 reaches the upper Formula-SWCT constraint of beta = 0.99.

In [ ]:
import json
import numpy as np

seeds = [42, 43, 44]

baseline_accs = []
sct_accs = []
sct_betas = []

formula_accs = []
formula_val_accs = []
formula_betas = []

for seed in seeds:

    # Baseline
    with open(
        f"results/base_imagenet_to_medmnist-pathmnist_resnet18_seed{seed}.json",
        "r"
    ) as f:
        baseline = json.load(f)

    # S-CT
    with open(
        f"results/ct_imagenet_to_medmnist-pathmnist_resnet18_seed{seed}.json",
        "r"
    ) as f:
        sct = json.load(f)

    # Formula-SWCT
    with open(
        f"results/formula_swct_imagenet_to_medmnist-pathmnist_resnet18_seed{seed}.json",
        "r"
    ) as f:
        formula = json.load(f)

    baseline_accs.append(baseline["accuracy"])
    sct_accs.append(sct["accuracy"])
    sct_betas.append(sct["beta"])

    formula_accs.append(formula["test_acc"])
    formula_val_accs.append(formula["best_val_acc"])
    formula_betas.append(formula["predicted_betas"])


baseline_accs = np.array(baseline_accs)
sct_accs = np.array(sct_accs)
formula_accs = np.array(formula_accs)
formula_betas = np.array(formula_betas)


print("=" * 70)
print("PATHMNIST RESULTS — RESNET-18")
print("=" * 70)

print("\nBASELINE")
for seed, acc in zip(seeds, baseline_accs):
    print(f"Seed {seed}: {acc:.2f}%")

print(
    f"Mean: {baseline_accs.mean():.2f}% "
    f"± {baseline_accs.std(ddof=1):.2f}"
)


print("\nS-CT")
for seed, acc, beta in zip(seeds, sct_accs, sct_betas):
    print(
        f"Seed {seed}: "
        f"test={acc:.2f}% | beta={beta:.2f}"
    )

print(
    f"Mean: {sct_accs.mean():.2f}% "
    f"± {sct_accs.std(ddof=1):.2f}"
)


print("\nFORMULA-SWCT")
for seed, acc, val, betas in zip(
    seeds,
    formula_accs,
    formula_val_accs,
    formula_betas
):
    print(
        f"Seed {seed}: "
        f"test={acc:.2f}% | "
        f"best val={val:.2f}% | "
        f"betas={[round(x, 6) for x in betas]}"
    )

print(
    f"\nMean: {formula_accs.mean():.2f}% "
    f"± {formula_accs.std(ddof=1):.2f}"
)

print(
    "\nMean predicted betas:",
    np.round(formula_betas.mean(axis=0), 6)
)

print("\nMETHOD DIFFERENCES")
print(
    f"Formula-SWCT - Baseline: "
    f"{formula_accs.mean() - baseline_accs.mean():+.2f} pp"
)

print(
    f"Formula-SWCT - S-CT: "
    f"{formula_accs.mean() - sct_accs.mean():+.2f} pp"
)

# PathMNIST Results Summary

The complete three-seed comparison will be finalized after the missing Baseline/S-CT seed-43 and seed-44 experiments are executed.

The currently recovered results are:

### Seed 42 reference methods

- Baseline: **86.82%**
- S-CT: **87.70%**
- Selected S-CT beta: **0.83**
- Best S-CT validation accuracy: **92.82%**

### Formula-SWCT

| Seed | Test Accuracy |
|---:|---:|
| 42 | **87.30%** |
| 43 | **86.99%** |
| 44 | **86.84%** |

Formula-SWCT mean:

**87.04 ± 0.23%**

Formula-SWCT predicted:

**[0.990000, 0.978555, 0.986764, 0.890690]**

for all three completed runs.

The final Baseline, S-CT, and Formula-SWCT three-seed comparison will be reported after the remaining reference runs are completed.